# Graph Based Analysis

## Setup & Import

### Import the needed libraries

In [1]:
from topologicpy.Vertex import Vertex
from topologicpy.Wire import Wire
from topologicpy.Face import Face
from topologicpy.Shell import Shell
from topologicpy.Topology import Topology
from topologicpy.Dictionary import Dictionary
from topologicpy.Helper import Helper
from topologicpy.Grid import Grid
from topologicpy.Graph import Graph
from topologicpy.Color import Color

from utils import reset_dictionaries, transfer_dicts_by_key

c:\Users\cutro\miniconda3\envs\graphml\Lib\site-packages\tqdm\auto.py:21: TqdmWarning: IProgress not found. Please update jupyter and ipywidgets. See https://ipywidgets.readthedocs.io/en/stable/user_install.html
  from .autonotebook import tqdm as notebook_tqdm


In [2]:
print(Helper.Version())

Helper.CheckVersion - Error: Could not fetch data from PyPI. Returning None
None


### Set renderer

In [3]:
renderer = "vscode"

### Import BREP floorplan

In [4]:
floorplan = Topology.ByBREPPath(r"Assets\Spreefeld\spreefeld_gf_face.brep")

### Calculate floorpplan area

In [5]:
area = Face.Area(floorplan)
print("Area of the floorplan:", area)

Area of the floorplan: 8743.568723


### Show geometry

In [6]:
Topology.Show(floorplan,
              camera=[0,0,6],
              faceColor=[210,210,250],
              faceOpacity=1,
              edgeColor="white",
              edgeWidth=3,
              showVertices=False,
              backgroundColor="black",
              width=800,
              height=600,
              renderer = renderer)

## From Brep to Shell

### Create a grid overlay

In [7]:
b_r = Wire.BoundingRectangle(floorplan)
d = Topology.Dictionary(b_r)
xmin = Dictionary.ValueAtKey(d, "xmin")
xmax = Dictionary.ValueAtKey(d, "xmax")
ymin = Dictionary.ValueAtKey(d, "ymin")
ymax = Dictionary.ValueAtKey(d, "ymax")
width = Dictionary.ValueAtKey(d, "width")
length = Dictionary.ValueAtKey(d, "length")
uRange = list(range(0,int(width)+3,3)) #grid every 3 meters (0, 3, 6, 9, 12, ...), they are just lines
vRange = list(range(0,int(length)+3,3))

grid = Grid.EdgesByDistances(floorplan, clip=True, uRange=uRange, vRange=vRange)

### Show the geometry and the grid

In [8]:
Topology.Show(floorplan, grid,
              camera=[0,0,6],
              faceColor=[210,210,250],
              faceOpacity=1,
              edgeColor="grey",
              edgeWidth=3,
              showVertices=False,
              backgroundColor="black",
              width=800,
              height=600,
              renderer = renderer)

### Slice the floor plan with the grid to create a topologic shell

In [9]:
shell = Topology.Slice(floorplan, grid)
faces = Topology.Faces(shell)
# Assign a sequential unique face id to reference it later (e.g. "face_21")
for i, f in enumerate(faces):
    d = Dictionary.ByKeyValue("face_id", "face_"+str(i+1))
    f = Topology.SetDictionary(f, d)

### Show the resulting shell

In [10]:
Topology.Show(shell,
              camera=[0,0,6],
              faceColor=[210,210,250],
              faceOpacity=0.9,
              edgeColor="black",
              edgeWidth=3,
              showVertices=False,
              backgroundColor="black",
              width=800,
              height=600,
              renderer = renderer)

## From Shell to Graph

### Derive navigation and analysis graphs from the shell

In [11]:
# Note: Graph nodes automatically inherit the dictionaries of the entities they 
navigation_graph = Graph.ByTopology(shell, direct=False, viaSharedTopologies=True) #use for the shortest path, it's going through shared edges to avoid to get outside the building
analysis_graph = Graph.ByTopology(shell)

### Derive and store the analysis graph vertices

In [12]:
g_verts = Graph.Vertices(analysis_graph)
print("Number of graph vertices:", len(g_verts))
g_edges = Graph.Edges(analysis_graph)
print("Number of graph edges:", len(g_edges))

Number of graph vertices: 1173
Number of graph edges: 2128


### Show analysis graph

In [13]:
Topology.Show(analysis_graph,
              camera=[0,0,6],
              vertexSize=4,
              vertexColor="red",
              edgeColor="lightgrey",
              backgroundColor="black",
              width=800,
              height=600,
              renderer=renderer)

## Spatial Intelligence

### Shortest Path (Use navigation graph)

The shortest path is calculated to evaluate distance between parts of the building.

In [32]:
import time

start_vertex = Vertex.ByCoordinates(xmin+2, ymax-2,0) # Upper left corner
end_vertex = Vertex.ByCoordinates(xmax-2, ymin+2,0) # Lower right corner
crg = Graph.CompiledRoutingGraph(navigation_graph, precomputeTurns=False) #optimization to get the shortest path faster
start = time.time()
shortest_path = Graph.ShortestPath(crg, vertexA=start_vertex, vertexB=end_vertex)
end = time.time()
print("Shortest Path Duration:", round(end-start, 2), "seconds")

# Straighten the shortest path (optional)
start = time.time()
straight_path = Wire.Straighten(shortest_path, host=floorplan)
end = time.time()
print("Straighten Wire Duration:", round(end-start, 2), "seconds")

print("Original Shortest Path Length:", round(Wire.Length(shortest_path), 2)) #this are meters
print("Straightened Shortened Path Length:", round(Wire.Length(straight_path), 2))
edges = Topology.Edges(shortest_path)
for edge in edges:
    d = Dictionary.ByKeysValues(["width", "color"], [7, "red"])
    edge = Topology.SetDictionary(edge, d)
edges = Topology.Edges(straight_path)
for edge in edges:
    d = Dictionary.ByKeysValues(["width", "color"], [7, "blue"])
    edge = Topology.SetDictionary(edge, d)

Shortest Path Duration: 1.51 seconds
Straighten Wire Duration: 5.98 seconds
Original Shortest Path Length: 208.58
Straightened Shortened Path Length: 172.03


In [33]:
Topology.Show(floorplan, shortest_path, straight_path,
              camera=[0,0,6],
              faceColor=[230,230,230],
              faceOpacity=1,
              edgeColorKey="color",
              edgeWidthKey="width",
              backgroundColor="white",
              width=800,
              height=600,
              renderer=renderer)

### Closeness Centrality (Integration)

**"How close is this node to all others?**

Closeness centyrality measures average distance to every other node. Smaller number is better, because it means less number of hops on average to get to the other nodes.

High closeness centrality indicates a space easy to reach from anywhere.

Example 
Consider a graph with 6 nodes:
* if node x can reach every other node through 1 hop, its average distance is 1;
* if node y needs 1 hop to reach one node and 2 hops to reach the remaining 4 nodes, its average distance is 1.8 [(2*4+1)/5=1.8]

* Closeness centrality is a graph metric that quantifies how close a node is to all other nodes by taking the reciprocal of the sum of its shortest path distances to every other node in the network.
* In space syntax, closeness centrality corresponds to global integration, measuring how spatially accessible or topologically shallow a space is within a configuration, thereby indicating its potential for movement flow and encounter density.

The closeness centrality is calculated to assess space centrality within the layout, expressing the efficiency of accessibility and circulation.

In [16]:
centrality_list = Graph.ClosenessCentrality(analysis_graph, colorScale="YlOrRd")

#Transfer the information from the graph back to the shell
reset_dictionaries(shell)
faces = Topology.Faces(shell)
_ = transfer_dicts_by_key(faces, g_verts, "face_id")

In [17]:
Topology.Show(faces,
              faceColorKey="cc_color",
              faceOpacity=1,
              showEdges=False,
              showVertices=False,
              camera=[0,0,6],
              backgroundColor="white",
              width=800,
              height=600,
              renderer=renderer)

### Betweenness Centrality (Choice)

**"How often do paths pass through this node?"**

Betweenness centrality measures how often a node lies on the shortest paths between other nodes.

High betwenness centrality indicates a strategic connector.

The betweenneess centrality is calculated to measure the dependence of the graph in each node.

In [18]:
centrality_list = Graph.BetweennessCentrality(analysis_graph, normalize=True, colorScale="thermal")

#Transfer the information from the graph back to the shell
reset_dictionaries(shell)
faces = Topology.Faces(shell)
_ = transfer_dicts_by_key(faces, g_verts, "face_id")

In [19]:
Topology.Show(faces,
              faceColorKey="bc_color",
              faceOpacity=1,
              showEdges=False,
              showVertices=False,
              camera=[0,0,6],
              backgroundColor="white",
              width=800,
              height=600,
              renderer=renderer)

### Community Detection (about 3 mins)

Community Detection analysis is calculated to define the clusters according to their position within the graph.

In [20]:
community_list = Graph.CommunityPartition(analysis_graph, colorScale="thermal") #partition the graph into communities, which are groups of nodes that are more connected to each other than to the rest of the graph, this allows to detect the "rooms" of the gallery 

#Transfer the information from the graph back to the shell
reset_dictionaries(shell)
_ = transfer_dicts_by_key(faces, g_verts, "face_id")

In [21]:
Topology.Show(faces,
              faceColorKey="cp_color", #community partition color
              faceOpacity=1,
              showEdges=False,
              showVertices=False,
              camera=[0,0,6],
              backgroundColor="white",
              width=800,
              height=600,
              renderer=renderer)

### Degree Centrality

**"How many direct connections?"**

Degree centrality measures how well each space is connected within the network.
In practice, it corresponds to the number of edges connected to a node. 

A high degree centrality indicates taht a space offers many immediate connections and therefore provides more direct choices for movement, while a low value suggests limited connectivity.

Degree Centrality is calculated to evaluate the connectivity of each space as it represents the number of direct connections each space has with other spaces.

Bin By Dictionary Key
* Use the community partition number (or colour) to separate the faces of the shell into different bins or categories
* Derive the outer boundary of each face group (perimeter) and make a face out of that perimeter

In [22]:
bins = Topology.BinByDictionaryKey(faces, key="community")
bin_dict = bins[0]
keys = list(bin_dict.keys())
face_groups = []
for key in keys:
    bin_faces = bin_dict[key]
    temp_shell = Shell.ByFaces(bin_faces)
    eb = Shell.ExternalBoundary(temp_shell)
    eb = Wire.RemoveCollinearEdges(eb)
    eb = Face.ByWire(eb)
    face_groups.append(eb)

In [23]:
Topology.Show(face_groups,
              faceOpacity=1,
              showEdges=True,
              edgeWidth=8,
              edgeColor="grey",
              camera=[0,0,6],
              backgroundColor="black",
              width=800,
              height=600,
              renderer=renderer)

In [24]:
#Create a new shell from new faces

new_shell = Shell.ByFaces(face_groups)

In [25]:
#Create a new graph from the new shell

new_graph = Graph.ByTopology(new_shell)
new_verts = Graph.Vertices(new_graph)
for v in new_verts:
    d = Dictionary.ByKeysValues(["color", "size"], ["red", 12])
    v = Topology.SetDictionary(v, d)

In [26]:
Topology.Show(new_shell, new_graph,
              faceOpacity=0.9,
              showEdges=True,
              showVertices=True,
              vertexSizeKey="size",
              vertexColorKey="color",
              camera=[0,0,6],
              backgroundColor="black",
              width=800,
              height=600,
              renderer=renderer)

In [27]:
#Compute degree centrality

degree_centralities = Graph.DegreeCentrality(new_graph, normalize=False)

In [28]:
# Transfer/Interpolate values from the new graph vertices to the original graph vertices

for v in g_verts:
    new_v = Vertex.InterpolateValue(v, vertices=new_verts, n=3, key="degree_centrality")

In [29]:
# Derive the colour of each vertex based on the interpolated value

minValue = min(degree_centralities)
maxValue = max(degree_centralities)
for v in g_verts:
    d = Topology.Dictionary(v)
    d_c = Dictionary.ValueAtKey(d, "degree_centrality")
    color = Color.AnyToHex(Color.ByValueInRange(d_c, minValue=minValue, maxValue=maxValue, colorScale="viridis"))
    d = Dictionary.SetValueAtKey(d, "dc_color", color)
    d = Dictionary.SetValueAtKey(d, "size", 16)
    v = Topology.SetDictionary(v, d)

In [30]:
# Transfer the information from the graph vertices to the faces of the original shell

reset_dictionaries(shell)
_ = transfer_dicts_by_key(faces, g_verts, "face_id")

In [31]:
Topology.Show(faces,
              faceColorKey="dc_color",
              faceOpacity=1,
              showEdges=False,
              showVertices=False,
              vertexSizeKey="size",
              vertexColorKey="dc_color",
              camera=[0,0,6],
              backgroundColor="white",
              width=800,
              height=600,
              renderer=renderer)